# Generate Music with an Open-Source Foundation Model (MusicGen)


**Model:** [MusicGen](https://huggingface.co/facebook/musicgen-small) by Meta AI — a pretrained,
open-source Transformer model that generates music directly from a text description.
**How:** We use the model exactly as released (a "foundation model") — no dataset, no training, no
fine-tuning. Just load it and generate.

### How it works
MusicGen is a Transformer (the same family of architecture as GPT) that was pretrained by Meta on a
large library of music. Instead of predicting the next *word*, it predicts the next *audio token* —
so generating music is really just "autocomplete for sound," guided by your text prompt. Because it's
already fully trained, we can generate brand-new music immediately, with about **10 lines of code**.

### Steps
1. Install the library
2. Load the pretrained model
3. Generate music from a text prompt
4. Listen to it / save it as a file


In [ ]:
!pip install -q -U transformers scipy


## Load the pretrained model

This downloads MusicGen (~300M parameters) the first time you run it (takes ~1 minute).

In [ ]:
from transformers import pipeline

music_generator = pipeline("text-to-audio", model="facebook/musicgen-small", device=0)
print("Model loaded and ready!")


Loading weights:   0%|          | 0/611 [00:00<?, ?it/s]

Model loaded and ready!


## Generate music from a text prompt

Change the `prompt` below to anything you like.

In [ ]:
prompt = "an upbeat lo-fi hip-hop track with a relaxed piano melody"

output = music_generator(prompt, forward_params={"do_sample": True})

sampling_rate = output["sampling_rate"]
audio_array = output["audio"]

# Some versions return shape (num_samples,), others (1, num_samples) — handle both
if audio_array.ndim > 1:
    audio_array = audio_array[0]

print("Generated", len(audio_array) / sampling_rate, "seconds of audio.")

Generated 29.94 seconds of audio.


In [ ]:
prompt = "an upbeat lo-fi hip-hop track with a relaxed piano melody"

output = music_generator(prompt, forward_params={"do_sample": True})

sampling_rate = output["sampling_rate"]
audio_array = output["audio"]

# Some versions return shape (num_samples,), others (1, num_samples) — handle both
if audio_array.ndim > 1:
    audio_array = audio_array[0]

print("Generated", len(audio_array) / sampling_rate, "seconds of audio.")

Generated 29.94 seconds of audio.


##  Listen to it

In [ ]:
from IPython.display import Audio, display

display(Audio(audio_array, rate=sampling_rate))


## Save it as a .wav file (and download it)

In [ ]:
from scipy.io.wavfile import write

write("generated_music.wav", rate=sampling_rate, data=audio_array)
print("Saved to generated_music.wav")

from google.colab import files
files.download("generated_music.wav")


Saved to generated_music.wav


<IPython.core.display.Javascript object>

<IPython.core.display.Javascript object>

## Generate a few different styles

Just a loop over a list of prompts — same function as above, called a few times.


In [ ]:
import numpy as np

prompts = [
    "a cheerful acoustic guitar folk tune",
    "an energetic electronic dance track with a heavy bassline",
    "a calm classical piano piece",
]

for i, p in enumerate(prompts):
    print("Prompt:", p)
    out = music_generator(p, generate_kwargs={"do_sample": True})
    out_audio = np.squeeze(np.asarray(out["audio"]))
    display(Audio(out_audio, rate=out["sampling_rate"]))

Prompt: a cheerful acoustic guitar folk tune


Prompt: an energetic electronic dance track with a heavy bassline


Prompt: a calm classical piano piece


## A pretrained open-source foundation model used directly for generation

No dataset, no training loop, no GPU fine-tuning — just a pretrained open-source foundation model
used directly for generation. This is sometimes called **zero-shot generation**: the model does the
task (text → music) purely from what it already learned during pretraining.

### Want to go further?
- Try a bigger model: `"facebook/musicgen-medium"` or `"facebook/musicgen-large"` (slower, higher quality)
- Try `forward_params={"do_sample": True, "guidance_scale": 3}` to control how closely the music follows the prompt
- Fine-tune the model on your own music dataset so it learns a specific genre or style (a bigger project — ask if you'd like that notebook too)
